# Gesture Painter with AI

In this notebook you can paint on a canvas using your hand. No mouse, no stylus, no touching anything! 

Your index fingertip becomes a brush, tracked in real time by a computer vision gesture detector. Once you've created your sketch, you can pass it (together with a prompt) to an image generation model to finalize your masterpiece!

## Gesture Controls

| Gesture | Action |
|---|---|
| **Pointing Up** (index finger extended) | Draw (your fingertip leaves a trail) |
| **Open Palm** | Clear (wipes the canvas clean) |

### How It Works

Each frame, the app passes the webcam picture to three small neural networks running in OpenCV. Together they find 21 points on your hand and name the gesture it is making. The models are attached to this notebook and are loaded by the **Set up hand tracking** cell below, which runs by itself when the notebook opens.

The app then reads the position of your **index fingertip** (`INDEX_FINGER_TIP`). When the gesture is `Pointing_Up`, it draws a line from the previous fingertip position to the current one.

All line segments are stored in a list and redrawn every frame on top of the live camera feed, so your painting persists as the video updates underneath.

Choose your brush color and size below, and then run the cell.

In [ ]:
#@title Set up hand tracking
import cv2

palm_net = cv2.dnn.readNet('/attachments/palm_detection_mediapipe_2023feb.onnx')
hand_net = cv2.dnn.readNet('/attachments/handpose_estimation_mediapipe_2023feb.onnx')
gesture_net = cv2.dnn.readNet('/attachments/gesture_classifier.onnx')

GESTURES = [
  'None', 'Closed_Fist', 'Open_Palm', 'Pointing_Up',
  'Thumb_Down', 'Thumb_Up', 'Victory', 'ILoveYou',
]

# Position of the index fingertip in each hand's list of 21 landmarks.
INDEX_FINGER_TIP = 8

import numpy as np

DETECTOR_SIZE = 192
LANDMARK_SIZE = 224

# The palm detector makes 2016 predictions, each relative to a fixed "anchor"
# point: 2 per cell of a 24x24 grid and 6 per cell of 12x12, stored as (x, y)
# cell centres from 0 to 1.
anchors = []
for grid, per_cell in ((24, 2), (12, 6)):
  xs, ys = np.meshgrid((np.arange(grid) + 0.5) / grid, (np.arange(grid) + 0.5) / grid)
  anchors.append(np.repeat(np.stack((xs.ravel(), ys.ravel()), axis=1), per_cell, axis=0))
anchors = np.concatenate(anchors)

def sigmoid(x):
  """Turn the network's raw scores into probabilities from 0 to 1."""
  return 1 / (1 + np.exp(-np.clip(x, -80, 80)))

def find_palms(frame, min_confidence=0.5, overlap_threshold=0.3):
  """Run the palm detector. Returns one array per palm of 7 keypoints (x, y)
  in frame pixels: the wrist, the bases of the index, middle, ring and
  little fingers, and two points at the base of the thumb."""
  # 1. Letterbox: shrink to fit 192x192 keeping the aspect ratio, padding
  #    both sides with black. The model wants RGB pixels from 0 to 1, in
  #    height x width x channel order (not a blobFromImage blob).
  height, width = frame.shape[:2]
  scale = DETECTOR_SIZE / max(height, width)
  resized = cv2.resize(frame, (int(width * scale), int(height * scale)))
  pad_x = (DETECTOR_SIZE - resized.shape[1]) // 2
  pad_y = (DETECTOR_SIZE - resized.shape[0]) // 2
  padded = cv2.copyMakeBorder(resized, pad_y, DETECTOR_SIZE - resized.shape[0] - pad_y,
                              pad_x, DETECTOR_SIZE - resized.shape[1] - pad_x, cv2.BORDER_CONSTANT)
  blob = cv2.cvtColor(padded, cv2.COLOR_BGR2RGB)[np.newaxis].astype(np.float32) / 255

  # 2. Run the network: 2016 rows of [box cx, cy, w, h, 7 keypoints (x, y)],
  #    offsets in 192-pixel units from each anchor, plus one score per row.
  palm_net.setInput(blob)
  output, scores = palm_net.forward(['Identity', 'Identity_1'])
  output = output[0].reshape(-1, 9, 2) / DETECTOR_SIZE
  confidences = sigmoid(scores[0, :, 0])

  # 3. Decode into frame pixels: add the anchor, then undo the letterbox.
  points = (output + anchors[:, np.newaxis]) * DETECTOR_SIZE / scale - (pad_x / scale, pad_y / scale)
  sizes = output[:, 1] * DETECTOR_SIZE / scale
  boxes = np.concatenate([points[:, 0] - sizes / 2, sizes], axis=1)

  # 4. Non-maximum suppression: drop boxes that overlap a more confident one.
  keep = cv2.dnn.NMSBoxes(boxes.tolist(), confidences.tolist(), min_confidence, overlap_threshold)
  return [points[i, 2:] for i in np.array(keep).flatten()]

def upright_crop(frame, centre, up, size, crop_size):
  """Cut a size x size square out of the frame, centred on `centre` and
  rotated so the `up` direction points to the top, then scale it to
  crop_size x crop_size. Returns the crop and the matrix that maps crop
  pixels back to frame pixels."""
  up = up / np.linalg.norm(up)
  right = np.array([-up[1], up[0]])
  half = size / 2
  top_left = centre + up * half - right * half
  top_right = centre + up * half + right * half
  bottom_left = centre - up * half - right * half
  to_crop = cv2.getAffineTransform(np.float32([top_left, top_right, bottom_left]),
                                   np.float32([[0, 0], [crop_size, 0], [0, crop_size]]))
  crop = cv2.warpAffine(frame, to_crop, (crop_size, crop_size))
  return crop, cv2.invertAffineTransform(to_crop)

def name_gesture(points, handedness):
  """Run the gesture classifier on one hand's 21 landmarks (x, y, z) and its
  handedness score. Returns the gesture name and how confident the model is."""
  def as_input(points, handedness):
    # Centre the hand on its palm and scale it to about 1 unit across, so
    # the answer doesn't depend on where the hand is or how big it looks.
    centred = points - points[[0, 1, 5, 9, 13, 17]].mean(axis=0)
    span = np.ptp(centred[:, :2], axis=0).max() + 1e-5
    return np.append((centred / span).ravel(), handedness).astype(np.float32)[np.newaxis]

  # The network looks at the hand and at its mirror image, so that left and
  # right hands are treated the same. It returns one score per gesture.
  gesture_net.setInput(as_input(points, handedness), 'hand')
  gesture_net.setInput(as_input(points * (-1, 1, 1), 1 - handedness), 'mirrored_hand')
  scores = gesture_net.forward()[0]
  best = int(scores.argmax())
  return GESTURES[best], float(scores[best])

def find_landmarks(frame, palm, min_confidence=0.5):
  """Run the landmark model on one palm's 7 keypoints, then name the gesture.
  Returns {"gesture", "confidence", "handedness", "landmarks"} with 21
  landmarks {"x", "y", "z"} in frame pixels, or None if the model doesn't
  think there is a hand there."""
  # 1. Turn the palm upright (wrist at the bottom, middle finger at the
  #    top) and measure the box around its keypoints along those
  #    directions. That box only covers the palm, so move it 0.4 of its
  #    height towards the fingers and make it 3 times bigger to fit the
  #    whole hand, then crop it.
  wrist, middle_knuckle = palm[0], palm[2]
  up = (middle_knuckle - wrist) / np.linalg.norm(middle_knuckle - wrist)
  right = np.array([-up[1], up[0]])
  along_right, along_up = palm @ right, palm @ up
  width, height = np.ptp(along_right), np.ptp(along_up)
  centre = (right * (along_right.min() + along_right.max()) / 2
            + up * ((along_up.min() + along_up.max()) / 2 + 0.4 * height))
  size = max(width, height) * 3
  crop, to_frame = upright_crop(frame, centre, up, size, LANDMARK_SIZE)
  blob = cv2.cvtColor(crop, cv2.COLOR_BGR2RGB)[np.newaxis].astype(np.float32) / 255

  # 2. Run the network: 21 rows of [x, y, z], a confidence, and a
  #    handedness score (0 = left hand, 1 = right hand).
  hand_net.setInput(blob)
  landmarks, confidence, handedness = hand_net.forward(['Identity', 'Identity_1', 'Identity_2'])
  if confidence[0, 0] < min_confidence:
    return None
  landmarks = landmarks[0].reshape(21, 3)

  # 3. Map crop pixels back to frame pixels. z is depth relative to the
  #    wrist, in the same (crop) pixel units, so scale it the same way.
  xy = np.c_[landmarks[:, :2], np.ones(21)] @ to_frame.T
  z = landmarks[:, 2] * size / LANDMARK_SIZE

  # 4. Name the gesture from the shape the 21 points make.
  gesture, gesture_confidence = name_gesture(np.c_[xy, z], float(handedness[0, 0]))
  return {
    'gesture': gesture,
    'confidence': round(gesture_confidence, 2),
    'handedness': 'Right' if handedness[0, 0] > 0.5 else 'Left',
    'landmarks': [{'x': int(x), 'y': int(y), 'z': float(d)} for (x, y), d in zip(xy, z)],
  }

def detect(frame, max_hands=2):
  """Find up to max_hands hands in a BGR frame. Each hand is a dict with
  "gesture", "confidence", "handedness" and "landmarks" (21 points).
  Handedness assumes a mirrored (selfie) frame, such as
  camera.capture_array() of a mirror=True camera."""
  hands = []
  for palm in find_palms(frame)[:max_hands]:
    hand = find_landmarks(frame, palm)
    if hand is not None:
      hands.append(hand)
  return hands

print("Hand tracking ready")

## Paint!

Set your brush color and size, then run the cell.
To change the brush mid-session: click **Stop** (■), adjust the controls, and run again.

Click **Stop** when you're done and move on to the following cell.

In [ ]:
from codetto import graphics2d, webcam

BRUSH_COLOR = "#ff4500" #@param ["#ff4500", "#00bfff", "#00ff88", "#ffff00", "#ffffff", "#ff69b4"]
BRUSH_SIZE  = 6         #@param {type:"slider", min:2, max:20, step:1}

canvas = graphics2d.canvas()
camera = webcam.start(canvas, mirror=True)
ctx    = canvas.get_context('2d')

strokes        = []
last_pos       = None
clear_cooldown = 0

try:
  while True:
    frame      = camera.capture_array()
    detections = detect(frame)
    canvas.draw_hands(detections)

    if detections:
      hand    = detections[0]
      tip     = hand['landmarks'][INDEX_FINGER_TIP]
      gesture = hand['gesture']

      if clear_cooldown > 0:
        clear_cooldown -= 1
        last_pos = None
      elif gesture == 'Pointing_Up':
        if last_pos:
          strokes.append((last_pos[0], last_pos[1],
                  tip['x'], tip['y'], BRUSH_COLOR, BRUSH_SIZE))
        last_pos = (tip['x'], tip['y'])
      elif gesture == 'Open_Palm':
        strokes.clear()
        ctx.clear_rect(0, 0, 9999, 9999)
        last_pos       = None
        clear_cooldown = 20
      else:
        last_pos = None
    else:
      last_pos = None

    for x1, y1, x2, y2, col, sz in strokes:
      ctx.stroke_style = col
      ctx.line_width   = sz
      ctx.begin_path()
      ctx.move_to(x1, y1)
      ctx.line_to(x2, y2)
      ctx.stroke()
finally:
  camera.stop()
  data_url = canvas.to_data_url(include_camera = False)
  assert data_url.startswith('data:image/png;base64,'), data_url[:50]
  print("Camera stopped.")

In [ ]:
#@title Let's extract your sketch...
graphics2d.display_image(data_url)

In [ ]:
#@title ...and pass your sketch to an image generation model
DESCRIPTION = "Hand drawn sketch of a flower" #@param
STYLE = "Watercolor" #@param ["Anime", "Cartoon", "Watercolor", "Photograph"]
TRANSFORMATION = f"I have a {DESCRIPTION}. Use it to create an image in the style of {STYLE}"

import openai

client = openai.OpenAI(
  base_url='https://openrouter.ai/api/v1',
  api_key=os.environ["OPENROUTER_API_KEY"]
)

print(f"Applying: {TRANSFORMATION}...")

response = client.chat.completions.create(
  model="black-forest-labs/flux.2-klein-4b",
  messages=[{
    "role": "user",
    "content": [
      {"type": "image_url", "image_url": {"url": data_url}},
      {"type": "text", "text": TRANSFORMATION}
    ]
  }],
  extra_body={"modalities": ["image"]}
)

transformed_url = response.choices[0].message.images[0]["image_url"]["url"]
graphics2d.display_image(transformed_url)

What did you create? What's one thing you'd change or add to make this a more powerful drawing tool?

## Ideas for students to extend this app in the classroom:

- **Color switching** — assign different colors to different gestures (e.g. `Victory` → blue, `Thumb_Up` → yellow)
- **Two-hand mode** — `detect` already finds up to two hands, so loop over `detections` and let each hand paint independently
- **Stamps** — detect `Thumb_Up` and paste an image at the fingertip position using `graphics2d.draw_image()`
- **Undo** — keep track of how many strokes were added per gesture and remove the last group on a specific gesture